# Learned Stage-Wise Curvature Tuning on Food101

This notebook evaluates Learned Stage-Wise Curvature Tuning (SW-CT) on the Food101 dataset using an ImageNet-pretrained ResNet-18.

Food101 is a large-scale food image-classification dataset containing 101 food categories. The dataset contains substantial variation in appearance, viewpoint, lighting, and presentation, making it useful for evaluating whether Learned SW-CT generalizes to a diverse natural-image classification task.

The experiments compare four conditions:

1. **Baseline** — the original pretrained ResNet with ReLU activations and a trained downstream classifier.
2. **Single-Parameter Curvature Tuning (S-CT)** — one global beta selected through validation-based exhaustive search.
3. **Learned SW-CT with fixed initialization** — four trainable stage-wise beta parameters initialized at 0.78.
4. **Learned SW-CT with random initialization** — four trainable stage-wise beta parameters independently initialized between 0.70 and 0.99.

Each condition is evaluated using seeds 42, 43, and 44.

Experiments are conducted for both 20 and 30 epochs to determine whether additional optimization improves classification performance or changes the learned stage-wise beta values.

Wall-clock execution time is also recorded to compare computational cost across Baseline, S-CT, and Learned SW-CT.

In [1]:
!nvidia-smi

Mon Oct  5 08:18:23 2026       
+-----------------------------------------------------------------------------------------+
| NVIDIA-SMI 610.43.02              KMD Version: 610.43.02     CUDA UMD Version: 13.3     |
+-----------------------------------------+------------------------+----------------------+
| GPU  Name                 Persistence-M | Bus-Id          Disp.A | Volatile Uncorr. ECC |
| Fan  Temp   Perf          Pwr:Usage/Cap |           Memory-Usage | GPU-Util  Compute M. |
|                                         |                        |               MIG M. |
|=========================================+========================+======================|
|   0  NVIDIA RTX A6000               Off |   00000000:0D:00.0 Off |                  Off |
| 30%   24C    P8             27W /  300W |       1MiB /  49140MiB |      0%      Default |
|                                         |                        |                  N/A |
+-----------------------------------------+-----

In [2]:
%cd /content

!git clone -b stage-wise-ct \
    https://github.com/Syed1611/curvature-tuning-research.git

%cd /content/curvature-tuning-research/src/curvature-tuning

!git branch --show-current
!git log -1 --oneline

/content
Cloning into 'curvature-tuning-research'...
remote: Enumerating objects: 592, done.
remote: Counting objects: 100% (264/264), done.
remote: Compressing objects: 100% (128/128), done.
remote: Total 592 (delta 166), reused 198 (delta 115), pack-reused 328 (from 1)
Receiving objects: 100% (592/592), 17.47 MiB | 7.56 MiB/s, done.
Resolving deltas: 100% (297/297), done.
/content/curvature-tuning-research/src/curvature-tuning
stage-wise-ct
6ec796c (HEAD -> stage-wise-ct, origin/stage-wise-ct, origin/HEAD) updated the notebook with outputs


## Environment Setup

The repository dependencies are installed before running the experiments.

After installation, the Colab runtime should be restarted so that the required package versions are loaded correctly.

In [3]:
%pip install -q -r requirements.txt
%pip install --force-reinstall --no-cache-dir "numpy==1.26.3"

Note: you may need to restart the kernel to use updated packages.
Defaulting to user installation because normal site-packages is not writeable
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 18.0/18.0 MB 24.7 MB/s  0:00:00 35.8 MB/s eta 0:00:01
  Attempting uninstall: numpy
    Found existing installation: numpy 1.26.3
    Uninstalling numpy-1.26.3:
      Successfully uninstalled numpy-1.26.3
Note: you may need to restart the kernel to use updated packages.


In [1]:
%cd /content/curvature-tuning-research/src/curvature-tuning

import os
import torch

os.environ["WANDB_MODE"] = "disabled"

print("Working directory:", os.getcwd())
print("PyTorch:", torch.__version__)
print("CUDA available:", torch.cuda.is_available())

if torch.cuda.is_available():
    print("GPU:", torch.cuda.get_device_name(0))

/content/curvature-tuning-research/src/curvature-tuning
Working directory: /content/curvature-tuning-research/src/curvature-tuning
PyTorch: 2.12.1+cu130
CUDA available: True
GPU: NVIDIA RTX A6000


## Food101 Dataset

Before running the experiments, the Food101 data loaders are checked to confirm that the downstream dataset can be loaded correctly.

The same dataset split and random seed protocol are used for Baseline, S-CT, and Learned SW-CT so that the methods are compared under the same conditions.

In [2]:
from PIL import Image

# Keep the original method; safe to rerun this cell.
if not hasattr(Image.Image, "_original_getexif_food101"):
    Image.Image._original_getexif_food101 = Image.Image.getexif

def safe_getexif(self):
    xmp = self.info.get("xmp")

    if isinstance(xmp, bytes):
        try:
            xmp.decode("utf-8")
        except UnicodeDecodeError:
            # Remove only the unreadable metadata from this loaded image.
            self.info.pop("xmp", None)

    return Image.Image._original_getexif_food101(self)

Image.Image.getexif = safe_getexif

print("Food101 metadata workaround enabled.")

Food101 metadata workaround enabled.


In [3]:
from utils.data import get_data_loaders

train_loader, test_loader, val_loader = get_data_loaders(
    "imagenet_to_food101",
    train_batch_size=32,
    test_batch_size=128,
    seed=42,
)

print("Train samples:", len(train_loader.dataset))
print("Validation samples:", len(val_loader.dataset))
print("Test samples:", len(test_loader.dataset))

images, labels = next(iter(train_loader))

print("Image batch shape:", images.shape)
print("Label batch shape:", labels.shape)
print("Labels:", labels[:10])

/home/ubuntu/.local/lib/python3.12/site-packages/tqdm/auto.py:21: TqdmWarning: IProgress not found. Please update jupyter and ipywidgets. See https://ipywidgets.readthedocs.io/en/stable/user_install.html
  from .autonotebook import tqdm as notebook_tqdm
Generating train split: 75750 examples [00:02, 32788.96 examples/s]
Generating test split: 25250 examples [00:00, 32935.16 examples/s]
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))


Train samples: 60600
Validation samples: 15150
Test samples: 25250
Image batch shape: torch.Size([32, 3, 224, 224])
Label batch shape: torch.Size([32])
Labels: tensor([13,  5,  1, 66, 89,  9, 81, 91, 35, 78])


# ResNet-18 Experiments

ResNet-18 is evaluated first because it was used during the initial development of Learned SW-CT.

The experiment compares Baseline, S-CT, fixed-initialization SW-CT, and random-initialization SW-CT.

All methods use the same ImageNet-pretrained backbone, Food101 dataset split, experimental seeds, and downstream training protocol.

## ResNet-18 — 20-Epoch Evaluation

The first evaluation uses 20 training epochs.

This provides the primary reference experiment and maintains compatibility with the earlier Learned SW-CT work.

### Methods

**Baseline**

The pretrained ResNet-18 retains its original ReLU activations. The backbone is frozen and only the downstream classifier is trained.

**S-CT**

The original Single-Parameter Curvature Tuning method searches over a single beta shared throughout the network. Candidate beta values from 0.70 to 1.00 are evaluated using validation performance, and the best candidate is evaluated on the test set.

The recorded S-CT execution time includes the complete beta search rather than only the final selected beta.

**Learned SW-CT — Fixed Initialization**

Four trainable beta parameters are assigned to the four ResNet stages. All four begin at beta = 0.78.

This preserves the initialization used in the original Learned SW-CT experiments.

**Learned SW-CT — Random Initialization**

Four trainable stage-wise beta parameters are initialized independently between 0.70 and 0.99.

The random initialization is generated deterministically from the experiment seed. This allows the experiment to test whether Learned SW-CT depends on the fixed 0.78 starting value while remaining reproducible.

In [4]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 42 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-05 08:31:23.506 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_food101_resnet18_seed42_epochs20.log
2026-10-05 08:31:23.511 | INFO     | __main__:main:78 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /home/ubuntu/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100%|██████████████████████████████████████| 44.7M/44.7M [00:00<00:00, 71.8MB/s]
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-05 08:38:09.774 | INFO     | __main__:main:105 - Testing baseline...
2026-10-05 08:38:09.802 | INFO     | __main__:main:116 - Number of trainable parameters: 51813
2026-10-05 08:38:09.802 | INFO     | __main__:main:117 - Starting transfer learning...
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-05 08:42:07.921 | INFO     | train:train_epoch

In [ ]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 43 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-03 00:24:21.299 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_food101_resnet18_seed43_epochs20.log
2026-10-03 00:24:21.303 | INFO     | __main__:main:78 - Running on cuda
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 00:31:52.375 | INFO     | __main__:main:105 - Testing baseline...
2026-10-03 00:31:52.394 | INFO     | __main__:main:116 - Number of trainable parameters: 51813
2026-10-03 00:31:52.394 | INFO     | __main__:main:117 - Starting transfer learning...
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 00:37:01.052 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 4.933236, Accuracy: 0.00%
2026-10-03 00:37:01.402 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 4.802910, Accuracy: 1.14%
2026-10-03 00:37:01.756 | INFO     | train:train_epoch:

In [ ]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 44 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-03 09:05:43.350 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_food101_resnet18_seed44_epochs20.log
2026-10-03 09:05:43.353 | INFO     | __main__:main:78 - Running on cuda
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 09:12:24.058 | INFO     | __main__:main:105 - Testing baseline...
2026-10-03 09:12:24.078 | INFO     | __main__:main:116 - Number of trainable parameters: 51813
2026-10-03 09:12:24.079 | INFO     | __main__:main:117 - Starting transfer learning...
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 09:17:20.353 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 4.936263, Accuracy: 3.12%
2026-10-03 09:17:20.665 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 4.819474, Accuracy: 1.27%
2026-10-03 09:17:20.983 | INFO     | train:train_epoch:

### Learned SW-CT with Fixed Beta Initialization

The original Learned SW-CT configuration is first reproduced using the fixed initialization:

\[[\beta_1,\beta_2,\beta_3,\beta_4]=[0.78,0.78,0.78,0.78].\]

The initial value is only a starting point. During training, the four beta parameters are optimized independently together with the downstream classifier.

These runs provide the reference against which random initialization will be compared.

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-03 13:09:58.840 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed42_epochs20_initfixed0.78_betalr0.01.log
2026-10-03 13:09:58.962 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 13:16:33.502 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 13:16:33.503 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 13:16:33.535 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 13:16:33.536 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 13:16:33.536 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-03 13:16:34.671 | INFO     | train

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-03 17:39:27.233 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed43_epochs20_initfixed0.78_betalr0.01.log
2026-10-03 17:39:27.296 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 17:46:45.324 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 17:46:45.324 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 17:46:45.357 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 17:46:45.358 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 17:46:45.358 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-03 17:46:46.537 | INFO     | train

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-03 19:51:13.739 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed44_epochs20_initfixed0.78_betalr0.01.log
2026-10-03 19:51:13.857 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 19:58:56.873 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 19:58:56.874 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 19:58:56.918 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 19:58:56.919 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 19:58:56.920 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-03 19:58:58.103 | INFO     | train

### Learned SW-CT with Random Beta Initialization

The fixed beta = 0.78 initialization may raise the question of whether Learned SW-CT performs well only because its starting point was informed by the earlier S-CT experiments.

To test this dependency, each of the four stage-wise beta parameters is now initialized independently from a uniform distribution between 0.70 and 0.99.

The initialization is reproducible: the random generator is seeded using the experiment seed. Therefore, each seed always receives the same initial beta vector.

If random initialization produces similar performance to the fixed 0.78 experiment, this provides evidence that the Learned SW-CT result is not dependent on a single hand-selected initialization.

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-03 22:08:54.978 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed42_epochs20_initrandom_betalr0.01.log
2026-10-03 22:08:55.081 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-03 22:16:33.782 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-03 22:16:33.782 | INFO     | __main__:main:394 - Requested initial stage betas: [0.924447, 0.827275, 0.948993, 0.902237]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 22:16:33.817 | INFO     | __main__:main:418 - Initial stage betas: [0.924447238445282, 0.827274739742279, 0.9489933848381042, 0.9022367000579834]
2026-10-03 22:16:33.818 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 22:16:33.819 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-03 22:16:35.160 | INFO

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-04 00:55:33.335 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed43_epochs20_initrandom_betalr0.01.log
2026-10-04 00:55:33.403 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-04 01:02:41.146 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-04 01:02:41.146 | INFO     | __main__:main:394 - Requested initial stage betas: [0.889167, 0.712695, 0.705809, 0.943372]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-04 01:02:41.185 | INFO     | __main__:main:418 - Initial stage betas: [0.8891667127609253, 0.7126947641372681, 0.7058085799217224, 0.9433716535568237]
2026-10-04 01:02:41.186 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-04 01:02:41.186 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-04 01:02:42.344 | IN

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-04 11:42:57.339 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed44_epochs20_initrandom_betalr0.01.log
2026-10-04 11:42:57.419 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100%|███████████████████████████████████████| 44.7M/44.7M [00:00<00:00, 148MB/s]
/usr/local/lib/python3.13/dist-packages/PIL/TiffImagePlugin.py:950: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-04 11:49:46.058 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-04 11:49:46.059 | INFO     | __main__:main:394 - Requested initial stage betas: [0.735544, 0.774853, 0.817674, 0.981063]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-04 11:49:46.099 | INFO     | __main__:main:418 - Initial stage betas: [0.7355440258979797, 0.7748528122901917, 0.8176735043525696, 0.98106336593627

# ResNet-18 — 30-Epoch Evaluation

The same experiments are now repeated for 30 epochs.

The purpose of increasing the training budget is to determine whether the 20-epoch results are limited by insufficient optimization.

If a method improves substantially with 30 epochs, this suggests that additional optimization is useful. If performance remains similar, it indicates that the method has largely stabilized within the original 20-epoch training budget.

All other experimental settings remain unchanged.

For random-initialization SW-CT, the same seed produces exactly the same initial four-beta vector in both the 20-epoch and 30-epoch experiments. Therefore, initialization is held constant while the training duration changes.

Execution time is again recorded to measure the computational cost of extending training from 20 to 30 epochs.

In [6]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 42 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-05 13:02:43.481 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_food101_resnet18_seed42_epochs30.log
2026-10-05 13:02:43.484 | INFO     | __main__:main:78 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-05 13:09:28.656 | INFO     | __main__:main:105 - Testing baseline...
2026-10-05 13:09:28.690 | INFO     | __main__:main:116 - Number of trainable parameters: 51813
2026-10-05 13:09:28.690 | INFO     | __main__:main:117 - Starting transfer learning...
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-05 13:13:29.476 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 4.725757, Accuracy: 3.12%
2026-10-05 13:13:30.101 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 4.784933, Accuracy: 1.02%
2026-10-05 13:13:30.743 | INFO     | train:train_epoch:

In [7]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 43 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-05 18:26:29.967 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_food101_resnet18_seed43_epochs30.log
2026-10-05 18:26:29.970 | INFO     | __main__:main:78 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-05 18:33:21.643 | INFO     | __main__:main:105 - Testing baseline...
2026-10-05 18:33:21.670 | INFO     | __main__:main:116 - Number of trainable parameters: 51813
2026-10-05 18:33:21.670 | INFO     | __main__:main:117 - Starting transfer learning...
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-05 18:37:16.834 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 4.933275, Accuracy: 0.00%
2026-10-05 18:37:17.366 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 4.802888, Accuracy: 1.14%
2026-10-05 18:37:17.837 | INFO     | train:train_epoch:

In [ ]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 44 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

All result files already exist. Exiting...


In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-06 08:37:48.885 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed42_epochs30_initfixed0.78_betalr0.01.log
2026-10-06 08:37:48.996 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-06 08:44:26.805 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-06 08:44:26.805 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-06 08:44:26.864 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-06 08:44:26.864 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-06 08:44:26.864 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-06 08:44:29.615 | INFO     | train

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-06 10:48:43.881 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed43_epochs30_initfixed0.78_betalr0.01.log
2026-10-06 10:48:43.984 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-06 10:55:38.380 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-06 10:55:38.380 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-06 10:55:38.452 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-06 10:55:38.452 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-06 10:55:38.453 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-06 10:55:41.269 | INFO     | train

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-06 12:55:32.592 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed44_epochs30_initfixed0.78_betalr0.01.log
2026-10-06 12:55:32.674 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-06 13:02:03.126 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-06 13:02:03.127 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-06 13:02:03.211 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-06 13:02:03.211 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-06 13:02:03.212 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-06 13:02:05.763 | INFO     | train

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-06 15:01:11.168 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed42_epochs30_initrandom_betalr0.01.log
2026-10-06 15:01:11.251 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-06 15:07:43.440 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-06 15:07:43.440 | INFO     | __main__:main:394 - Requested initial stage betas: [0.924447, 0.827275, 0.948993, 0.902237]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-06 15:07:43.530 | INFO     | __main__:main:418 - Initial stage betas: [0.924447238445282, 0.827274739742279, 0.9489933848381042, 0.9022367000579834]
2026-10-06 15:07:43.531 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-06 15:07:43.532 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-06 15:07:46.204 | INFO

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-06 17:07:26.190 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed43_epochs30_initrandom_betalr0.01.log
2026-10-06 17:07:26.284 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-06 17:14:18.148 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-06 17:14:18.148 | INFO     | __main__:main:394 - Requested initial stage betas: [0.889167, 0.712695, 0.705809, 0.943372]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-06 17:14:18.241 | INFO     | __main__:main:418 - Initial stage betas: [0.8891667127609253, 0.7126947641372681, 0.7058085799217224, 0.9433716535568237]
2026-10-06 17:14:18.241 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-06 17:14:18.242 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-06 17:14:21.114 | IN

In [ ]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds food101 \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-06 19:16:09.686 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_food101_resnet18_seed44_epochs30_initrandom_betalr0.01.log
2026-10-06 19:16:09.797 | INFO     | __main__:main:302 - Running on cuda
/usr/local/lib/python3.12/dist-packages/PIL/TiffImagePlugin.py:949: UserWarning: Truncated File Read
  warnings.warn(str(msg))
2026-10-06 19:22:44.061 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-06 19:22:44.062 | INFO     | __main__:main:394 - Requested initial stage betas: [0.735544, 0.774853, 0.817674, 0.981063]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-06 19:22:44.132 | INFO     | __main__:main:418 - Initial stage betas: [0.7355440258979797, 0.7748528122901917, 0.8176735043525696, 0.9810633659362793]
2026-10-06 19:22:44.132 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-06 19:22:44.133 | INFO     | __main__:main:439 - Total trainable parameters: 51817
2026-10-06 19:22:46.676 | IN